In [8]:
import numpy as np
import pandas as pd
from scipy.stats import gaussian_kde, pearsonr
import plotly.graph_objects as go
from plotly.subplots import make_subplots


def weighted_deming_regression(x, y, weights=None):
    """Verbatim from Martin Szinte's plot_utils.py — weighted orthogonal
    regression, symmetric when x and y are swapped."""
    x, y = np.array(x), np.array(y)
    weights = np.ones(len(x)) if weights is None else np.array(weights)
    weights = weights / weights.sum()
    x_mean, y_mean = np.sum(weights * x), np.sum(weights * y)
    sxx = np.sum(weights * (x - x_mean) ** 2)
    syy = np.sum(weights * (y - y_mean) ** 2)
    sxy = np.sum(weights * (x - x_mean) * (y - y_mean))
    slope = (syy - sxx + np.sqrt((syy - sxx) ** 2 + 4 * sxy ** 2)) / (2 * sxy)
    intercept = y_mean - slope * x_mean
    return slope, intercept



def make_corr_data(df_rdm, df_odm, rois, corr_params, corr_param_ranges,
            merge_keys=('roi', 'hemi', 'num_vert'), grid_size=100,
            rsq_threshold=0.0):
    data = pd.merge(df_rdm, df_odm, on=list(merge_keys), suffixes=('_RDM', '_ODM'))

    kde_frames, reg_rows = [], []
    for corr_param in corr_params:
        param_range = corr_param_ranges[corr_param]
        xx, yy = np.meshgrid(np.linspace(*param_range, grid_size),
                              np.linspace(*param_range, grid_size))
        grid_points = np.vstack([xx.ravel(), yy.ravel()])

        for roi in rois:
            df_roi = data.loc[data['roi'] == roi]
            x_vals = df_roi[f'{corr_param}_RDM'].values
            y_vals = df_roi[f'{corr_param}_ODM'].values
            r2_combined = (df_roi['prf_rsq_RDM'].values + df_roi['prf_rsq_ODM'].values) / 2

            # exclude NaNs AND sub-threshold/negative-rsq vertices — gaussian_kde's
            # weights must be >= 0, and low-rsq vertices are noise anyway
            mask = (~(np.isnan(x_vals) | np.isnan(y_vals) | np.isnan(r2_combined))
                    & (df_roi['prf_rsq_RDM'].values > rsq_threshold)
                    & (df_roi['prf_rsq_ODM'].values > rsq_threshold))
            x_vals, y_vals, r2_combined = x_vals[mask], y_vals[mask], r2_combined[mask]
            n_vertex = len(x_vals)
            mean_r2_weight = np.nanmean(r2_combined) if n_vertex > 0 else np.nan

            if n_vertex > 1:
                r2_norm = r2_combined / r2_combined.sum()
                try:
                    kde = gaussian_kde(np.vstack([x_vals, y_vals]), weights=r2_norm)
                    density = kde(grid_points).reshape(grid_size, grid_size)
                except np.linalg.LinAlgError:
                    density = np.full((grid_size, grid_size), np.nan)
            else:
                r2_norm, density = np.array([]), np.full((grid_size, grid_size), np.nan)

            kde_frames.append(pd.DataFrame({'corr_param': corr_param, 'roi': roi,
                                             'x_grid': xx.ravel(), 'y_grid': yy.ravel(),
                                             'density': density.ravel()}))

            if n_vertex > 2:
                slope, intercept = weighted_deming_regression(x_vals, y_vals, r2_norm)
                r_val, p_val = pearsonr(x_vals, y_vals)
                r2_pearson = r_val ** 2
            else:
                slope = intercept = r2_pearson = p_val = np.nan

            reg_rows.append({'corr_param': corr_param, 'roi': roi, 'slope': slope,
                              'intercept': intercept, 'r2_pearson': r2_pearson,
                              'p_value': p_val, 'n_vertex': n_vertex,
                              'mean_r2_weight': mean_r2_weight})

    return pd.concat(kde_frames, ignore_index=True), pd.DataFrame(reg_rows)


def corr_plot(df_kde, df_reg, rois, corr_params, corr_param_ranges, roi_colors,
              axis_labels, x_prefix='RDM', y_prefix='ODM', cell_size=220, margin=90):
    """Adapted from Martin Szinte's corr_plot: rows = ROIs, cols = corr_params,
    KDE contour + identity line + weighted regression line, in-memory."""
    rows, cols = len(rois), len(corr_params)
    fig = make_subplots(rows=rows, cols=cols, print_grid=False,
                         horizontal_spacing=0.03, vertical_spacing=0.03)

    for l, corr_param in enumerate(corr_params):
        param_range = corr_param_ranges[corr_param]
        df_kde_p = df_kde[df_kde['corr_param'] == corr_param]
        df_reg_p = df_reg[df_reg['corr_param'] == corr_param]
        x_grid = np.sort(df_kde_p['x_grid'].unique())
        y_grid = np.sort(df_kde_p['y_grid'].unique())

        for j, roi in enumerate(rois):
            roi_color = roi_colors[roi]
            r, g, b = [int(v) for v in roi_color.replace('rgb(', '').replace(')', '').split(',')]

            df_roi = df_kde_p[df_kde_p['roi'] == roi].sort_values(['y_grid', 'x_grid'])
            density = df_roi['density'].values.reshape(len(y_grid), len(x_grid))
            d_max = np.nanmax(density)
            density_norm = density / d_max if d_max > 0 else density

            line_xy = np.linspace(*param_range, 50)
            fig.add_trace(go.Scatter(x=line_xy, y=line_xy, mode='lines',
                                      line=dict(color='rgba(0,0,0,0.5)', width=2, dash='dash'),
                                      showlegend=False), row=j + 1, col=l + 1)

            fig.add_trace(go.Contour(
                x=x_grid, y=y_grid, z=density_norm,
                colorscale=[[0, f'rgba({r},{g},{b},0)'], [1, f'rgba({r},{g},{b},1)']],
                showscale=False,
                contours=dict(coloring='fill', showlines=False, start=0.05, end=1.0, size=0.05),
                zmin=0, zmax=1), row=j + 1, col=l + 1)

            reg_row = df_reg_p[df_reg_p['roi'] == roi]
            if len(reg_row) and not np.isnan(reg_row['slope'].values[0]):
                slope, intercept = reg_row['slope'].values[0], reg_row['intercept'].values[0]
                reg_x = np.linspace(*param_range, 50)
                fig.add_trace(go.Scatter(x=reg_x, y=slope * reg_x + intercept, mode='lines',
                                          line=dict(color=roi_color, width=3),
                                          showlegend=False), row=j + 1, col=l + 1)

            fig.add_annotation(x=param_range[1] - 0.05 * (param_range[1] - param_range[0]),
                                y=param_range[0] + 0.05 * (param_range[1] - param_range[0]),
                                text=roi, xanchor='right', yanchor='bottom',
                                showarrow=False, font_color=roi_color, row=j + 1, col=l + 1)

            x_title = f"{x_prefix} – {axis_labels[corr_param]}" if j == rows - 1 else ''
            y_title = f"{y_prefix} – {axis_labels[corr_param]}" if l == 0 else ''
            fig.update_xaxes(title_text=x_title, range=param_range, showline=True, row=j + 1, col=l + 1)
            fig.update_yaxes(title_text=y_title, range=param_range, showline=True, row=j + 1, col=l + 1)

    fig.update_layout(height=cell_size * rows + margin, width=cell_size * cols + margin,
                       showlegend=False, plot_bgcolor='white')
    #fig.write_image("/Users/sinakling/Desktop/Sacloc_correlation_test.pdf")
    return fig

In [16]:
import os, sys
import numpy as np
import pandas as pd

sys.path.append('/Users/sinakling/disks/meso_H/projects/pRF_analysis/analysis_code/utils')  
from surface_utils import load_surface
from pycortex_utils import get_rois, set_pycortex_config_file

subject = 'sub-11'

set_pycortex_config_file('/Users/sinakling/disks/meso_shared/RetinoMaps/derivatives/pp_data/cortex')

# same order fit2deriv() writes for the CSS model (analysis_code/utils/prf_utils.py)
maps_names_css = ['prf_rsq', 'prf_ecc', 'prf_polar_real', 'prf_polar_imag',
                   'prf_size', 'prf_amp', 'prf_baseline', 'prf_x', 'prf_y',
                   'prf_hrf_1', 'prf_hrf_2', 'prf_n']

def deriv_gii_to_df(deriv_fns_by_hemi, rois, pycortex_subject, rois_method='rois-group-mmp'):
    """deriv_fns_by_hemi: {'hemi-L': '..._deriv.func.gii', 'hemi-R': '..._deriv.func.gii'}
    Mirrors the per-hemi loop in make_tsv_css.py, for one design matrix."""
    df_rois = pd.DataFrame()
    for hemi, deriv_fn in deriv_fns_by_hemi.items():
        _, deriv_mat = load_surface(deriv_fn)  # (n_params, n_vertices), via nb.load + vstack(darrays)
        assert deriv_mat.shape[0] == len(maps_names_css), \
            f"{deriv_fn} has {deriv_mat.shape[0]} frames, expected {len(maps_names_css)} — check loo_r2"

        roi_verts = get_rois(subject=pycortex_subject, surf_format='fsnative',
                              rois_type=rois_method, mask=True, rois=rois, hemis=hemi)
        for roi in roi_verts.keys():
            data_dict = {col: deriv_mat[i, roi_verts[roi]] for i, col in enumerate(maps_names_css)}
            data_dict['roi'] = roi
            data_dict['hemi'] = hemi
            data_dict['num_vert'] = np.where(roi_verts[roi])[0]
            df_rois = pd.concat([df_rois, pd.DataFrame(data_dict)], ignore_index=True)
    return df_rois

rois = ['V1', 'V2', 'V3', 'V3AB', 'LO', 'VO', 'hMT+', 'iIPS', 'sIPS', 'iPCS', 'sPCS', 'mPCS']

df_rdm = deriv_gii_to_df(
    {'hemi-L': f'/Users/sinakling/disks/meso_shared/RetinoMaps/derivatives/pp_data/{subject}/fsnative/pmf/prf_derivatives/{subject}_task-SacLoc_hemi-L_fmriprep_dct_z-score_concat_pmf-css-rdm_deriv.func.gii',
     'hemi-R': f'/Users/sinakling/disks/meso_shared/RetinoMaps/derivatives/pp_data/{subject}/fsnative/pmf/prf_derivatives/{subject}_task-SacLoc_hemi-R_fmriprep_dct_z-score_concat_pmf-css-rdm_deriv.func.gii'},
    rois, pycortex_subject=subject)

df_odm = deriv_gii_to_df(
    {'hemi-L': f'/Users/sinakling/disks/meso_shared/RetinoMaps/derivatives/pp_data/{subject}/fsnative/pmf/prf_derivatives/{subject}_task-SacLoc_hemi-L_fmriprep_dct_z-score_concat_pmf-css-odm_deriv.func.gii',
     'hemi-R': f'/Users/sinakling/disks/meso_shared/RetinoMaps/derivatives/pp_data/{subject}/fsnative/pmf/prf_derivatives/{subject}_task-SacLoc_hemi-R_fmriprep_dct_z-score_concat_pmf-css-odm_deriv.func.gii'},
    rois, pycortex_subject=subject)

In [3]:
corr_params = ['prf_ecc', 'prf_size', 'prf_rsq']          # add 'prf_n' etc. freely
corr_param_ranges = {'prf_ecc': [0, 15], 'prf_size': [0, 12], 'prf_rsq': [0, 1]}
axis_labels = {'prf_ecc': 'pRF ecc. (dva)', 'prf_size': 'pRF size (dva)', 'prf_rsq': 'pRF R²'}
rois = ['V1', 'V2', 'V3', 'V3AB', 'LO', 'VO', 'hMT+', 'iIPS', 'sIPS', 'iPCS', 'sPCS', 'mPCS']
roi_colors = {roi: 'rgb(31,119,180)' for roi in rois}      # swap in his real ROI palette if you have it

In [17]:
df_kde, df_reg = make_corr_data(df_rdm, df_odm, rois, corr_params, corr_param_ranges,
                                 merge_keys=('roi', 'hemi', 'num_vert'))
fig = corr_plot(df_kde, df_reg, rois, corr_params, corr_param_ranges, roi_colors, axis_labels)

In [18]:
fig.show()